# Bronze layer

In [0]:
%sql
CREATE OR REPLACE TABLE panerai_project.dev.panerai_data_bronze_dev
(
  CONSTRAINT check_dup EXPECT (dup_count = 1)
)
COMMENT 'Bronze layer ingestion of all Panerai watches data from volume storage'
AS SELECT *, _metadata.file_path AS file_path
  FROM read_files(
  '/Volumes/panerai_project/dev/panerai_data',
  format => 'csv',
  header => true,
  inferSchema => true
);

num_affected_rows,num_inserted_rows


In [0]:
%sql
select * from panerai_project.dev.panerai_data_bronze_dev
limit 5;

title,reference,price,url,diameter_tag,edition,comment,total_articles,collection,currency,country,date,_rescued_data,file_path
Luminor Due,PAM01550,7 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01671,7 600 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01552,7 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01123,8 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01672,7 600 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv


# Silver layer

In [0]:
df = spark.read.table("panerai_project.dev.panerai_data_bronze_dev")

display(df.limit(5))

title,reference,price,url,diameter_tag,edition,comment,total_articles,collection,currency,country,date,_rescued_data,file_path
Luminor Due,PAM01550,7 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01671,7 600 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01552,7 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01123,8 200 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01672,7 600 €,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv


### Drop rows with Reference missing values

In [0]:
df = df.dropna(subset=["reference"])

print("Number of records with Reference as nulls: ", df.filter(df.reference.isNull()).count())

Number of records with Reference as nulls:  0


#### 1. Clean price column

In [0]:
from pyspark.sql.functions import regexp_replace, col

# Remove all non-digit characters (currency symbols, spaces, commas, dots, letters)
# then cast to a clean numeric value

df = df.withColumn(
    "price",
    regexp_replace(col("price"), r"[^0-9]", "").cast("int")
)

df.display()

title,reference,price,url,diameter_tag,edition,comment,total_articles,collection,currency,country,date,_rescued_data,file_path
Luminor Due,PAM01550,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01671,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01552,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01123,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01672,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due Luna,PAM01181,24400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01181-luminor-due-luna-goldtech-madreperla.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01280,21400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01280-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due TuttoOro,PAM01326,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01326-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due TuttoOro,PAM01182,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01182-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv
Luminor Due,PAM01508,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01508-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv


#### 2. Clean diameter_tag column

In [0]:
df = df.withColumn(
    "diameter (mm)",
    regexp_replace(col("diameter_tag"), r"[^0-9]", "").cast("int")
)

df.display()

title,reference,price,url,diameter_tag,edition,comment,total_articles,collection,currency,country,date,_rescued_data,file_path,diameter (mm)
Luminor Due,PAM01550,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due,PAM01671,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42
Luminor Due,PAM01552,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due,PAM01123,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due,PAM01672,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42
Luminor Due Luna,PAM01181,24400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01181-luminor-due-luna-goldtech-madreperla.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due,PAM01280,21400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01280-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due TuttoOro,PAM01326,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01326-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due TuttoOro,PAM01182,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01182-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38
Luminor Due,PAM01508,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01508-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,France,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38


#### 3. Handle reference duplicates

In [0]:
import yaml

# Load YAML
with open("./ref_corrected_url.yaml", "r") as f:
    ref_corrected_url = yaml.safe_load(f)

In [0]:
from pyspark.sql import functions as F

# Flatten YAML structure
corrections = [
    (ref, country, data["url"])
    for ref, countries in ref_corrected_url.items()
    for country, data in countries.items()
]

# Create small lookup DataFrame
correct_urls_df = spark.createDataFrame(
    corrections,
    ["reference", "country", "correct_url"]
)

In [0]:
df = (
    df
    .join(
        F.broadcast(correct_urls_df),
        on=["reference", "country"],
        how="left"
    )
    .filter(
        F.col("correct_url").isNull()
        |
        (F.col("url") == F.col("correct_url"))
    )
    .drop("correct_url")
)

#### 4. Converted price column

In [0]:
rate_exchange = {"USD": 
                 {"EUR" : 0.88},
                 "JPY": 
                 {"EUR" : 0.0056},
                 "AED": 
                 {"EUR" : 0.24},
                 "CHF": 
                 {"EUR" : 1.06},
                 "GBP": 
                 {"EUR" : 1.16},
                 "EUR": 
                 {"EUR" : 1}}

from pyspark.sql.functions import col, when, lit

# Build a chain of when() conditions, one per currency, to look up the rate
rate_expr = lit(1.0)  # default fallback
for currency, rates in rate_exchange.items():
    rate_expr = when(col("currency") == currency, lit(rates["EUR"])).otherwise(rate_expr)

df = df.withColumn("converted_price (EUR)", col("price") * rate_expr)

df.display()

reference,country,title,price,url,diameter_tag,edition,comment,total_articles,collection,currency,date,_rescued_data,file_path,diameter (mm),converted_price (EUR)
PAM01550,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0
PAM01671,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0
PAM01552,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0
PAM01123,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0
PAM01672,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0
PAM01181,France,Luminor Due Luna,24400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01181-luminor-due-luna-goldtech-madreperla.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,24400.0
PAM01280,France,Luminor Due,21400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01280-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,21400.0
PAM01326,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01326-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0
PAM01182,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01182-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0
PAM01508,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01508-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0


In [0]:
df.select(df.reference, df.price, df.currency, col("`converted_price (EUR)`")).filter(df.reference == "PAM01678").display()

reference,price,currency,converted_price (EUR)
PAM01678,17500,EUR,17500
PAM01678,2673000,JPY,14968.8
PAM01678,15300,CHF,16218
PAM01678,64600,AED,15504
PAM01678,15100,GBP,17516
PAM01678,18000,USD,15840
PAM01678,17500,EUR,17500
PAM01678,2673000,JPY,14968.8
PAM01678,15300,CHF,16218
PAM01678,64600,AED,15504


#### 5. Handle missing values

In [0]:
from pyspark.sql.functions import col, count, when, isnan

# Count missing (null or NaN) values per column
missing_counts = df.select([
    count(when(
        col(c).isNull() | isnan(col(c))
        if df.schema[c].dataType.typeName() in ("double", "float")
        else col(c).isNull(),
        c
    )).alias(c)
    for c in df.columns
])

print("Missing values per column:")
missing_counts.display()

Missing values per column:


reference,country,title,price,url,diameter_tag,edition,comment,total_articles,collection,currency,date,_rescued_data,file_path,diameter (mm),converted_price (EUR)
0,0,0,30,0,0,2099,1751,0,0,0,0,2513,0,0,30


In [0]:
from pyspark.sql import functions as F

df = (
    df
    .withColumn(
        "price_display",
        F.when(
            F.col("price").isNull(),
            F.lit("Contact store directly")
        ).otherwise(
            F.col("price").cast("string")
        )
    )
)

df = (
    df
    .withColumn(
        "converted_price_display",
        F.when(
            F.col("`converted_price (EUR)`").isNull(),
            F.lit("Contact store directly")
        ).otherwise(
            F.col("`converted_price (EUR)`").cast("string")
        )
    )
)

df.display()

reference,country,title,price,url,diameter_tag,edition,comment,total_articles,collection,currency,date,_rescued_data,file_path,diameter (mm),converted_price (EUR),price_display,converted_price_display
PAM01550,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0,7200,7200.0
PAM01671,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0,7600,7600.0
PAM01552,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0,7200,7200.0
PAM01123,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0,8200,8200.0
PAM01672,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0,7600,7600.0
PAM01181,France,Luminor Due Luna,24400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01181-luminor-due-luna-goldtech-madreperla.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,24400.0,24400,24400.0
PAM01280,France,Luminor Due,21400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01280-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,21400.0,21400,21400.0
PAM01326,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01326-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0,42900,42900.0
PAM01182,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01182-luminor-due-tuttooro.html,38 mm,null,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0,42900,42900.0
PAM01508,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01508-luminor-due.html,38 mm,null,null,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0,8200,8200.0


In [0]:
from pyspark.sql.functions import col, when

df = (
    df
    .withColumn("edition", when(col("edition").isNull(), "unknown").otherwise(col("edition")))
    .withColumn("comment", when(col("comment").isNull(), "unknown").otherwise(col("comment")))
)

df.display()

reference,country,title,price,url,diameter_tag,edition,comment,total_articles,collection,currency,date,_rescued_data,file_path,diameter (mm),converted_price (EUR),price_display,converted_price_display
PAM01550,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01550-luminor-due.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0,7200,7200.0
PAM01671,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01671-luminor-due.html,42 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0,7600,7600.0
PAM01552,France,Luminor Due,7200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01552-luminor-due.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,7200.0,7200,7200.0
PAM01123,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01123-luminor-due.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0,8200,8200.0
PAM01672,France,Luminor Due,7600,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01672-luminor-due.html,42 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,42,7600.0,7600,7600.0
PAM01181,France,Luminor Due Luna,24400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01181-luminor-due-luna-goldtech-madreperla.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,24400.0,24400,24400.0
PAM01280,France,Luminor Due,21400,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01280-luminor-due.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,21400.0,21400,21400.0
PAM01326,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01326-luminor-due-tuttooro.html,38 mm,unknown,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0,42900,42900.0
PAM01182,France,Luminor Due TuttoOro,42900,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01182-luminor-due-tuttooro.html,38 mm,unknown,Boutique Exclusive,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,42900.0,42900,42900.0
PAM01508,France,Luminor Due,8200,https://www.panerai.com/fr/fr/collections/watch-collection/luminor-due/pam01508-luminor-due.html,38 mm,unknown,unknown,27,Luminor Due,EUR,01-10-2026,null,dbfs:/Volumes/panerai_project/dev/panerai_data/01-10-2026/France/panerai_watches_France_Luminor%20Due_01-10-2026.csv,38,8200.0,8200,8200.0


In [0]:
from pyspark.sql.functions import col, count, when, isnan

# Count missing (null or NaN) values per column
missing_counts = df.select([
    count(when(
        col(c).isNull() | isnan(col(c))
        if df.schema[c].dataType.typeName() in ("double", "float")
        else col(c).isNull(),
        c
    )).alias(c)
    for c in df.columns
])

print("Missing values per column:")
missing_counts.display()

Missing values per column:


reference,country,title,price,url,diameter_tag,edition,comment,total_articles,collection,currency,date,_rescued_data,file_path,diameter (mm),converted_price (EUR),price_display,converted_price_display
0,0,0,30,0,0,0,0,0,0,0,0,2513,0,0,30,0,0


In [0]:
df.createOrReplaceTempView("df")

spark.sql("""
CREATE OR REPLACE TABLE panerai_project.dev.panerai_data_silver_dev
(
    CONSTRAINT valid_country EXPECT (Country IN ('France', 'USA', 'UK', 'UAE', 'Switzerland', 'Japan')),
    CONSTRAINT valid_collection EXPECT (Collection IN ('Radiomir', 'Luminor', 'Submersible', 'Luminor Due')),
    CONSTRAINT no_duplicate_ref_price_country EXPECT (dup_count = 1)
)
COMMENT 'Silver layer cleaning of all Panerai watches data from bronze layer'
AS SELECT 
    title as Title,
    collection as Collection,
    reference as Reference,
    price as Original_Price,
    price_display as Original_Price_Display,
    currency as Original_Currency,
    `converted_price (EUR)` as Converted_Price_EUR,
    converted_price_display as Converted_Price_Display_EUR,
    url as Url,
    `diameter (mm)` as Diameter,
    country as Country,
    edition as Edition,
    comment as Comment,
    total_articles as Total_Articles,
    date as Date,
    _rescued_data,
    COUNT(*) OVER (PARTITION BY reference, price, country, date) as dup_count   
FROM df
""")

DataFrame[num_affected_rows: bigint, num_inserted_rows: bigint]

In [0]:
%sql
select * from panerai_project.dev.panerai_data_silver_dev
limit 5;

Title,Collection,Reference,Original_Price,Original_Price_Display,Original_Currency,Converted_Price_EUR,Converted_Price_Display_EUR,Url,Diameter,Country,Edition,Comment,Total_Articles,Date,_rescued_data,dup_count
Luminor,Luminor,PAM00422,11000,11000,GBP,12760.0,12760.0,https://www.panerai.com/gb/en/collections/watch-collection/luminor/pam00422-luminor.html,47,UK,unknown,unknown,61,01-10-2026,null,1
Luminor,Luminor,PAM00422,11000,11000,GBP,12760.0,12760.0,https://www.panerai.com/gb/en/collections/watch-collection/luminor/pam00422-luminor.html,47,UK,unknown,unknown,61,02-10-2026,null,1
Luminor,Luminor,PAM00422,11000,11000,GBP,12760.0,12760.0,https://www.panerai.com/gb/en/collections/watch-collection/luminor/pam00422-luminor.html,47,UK,unknown,unknown,62,30-09-2026,null,1
Luminor,Luminor,PAM00422,11200,11200,CHF,11872.0,11872.0,https://www.panerai.com/ch/en/collections/watch-collection/luminor/pam00422-luminor.html,47,Switzerland,unknown,unknown,62,01-10-2026,null,1
Luminor,Luminor,PAM00422,11200,11200,CHF,11872.0,11872.0,https://www.panerai.com/ch/en/collections/watch-collection/luminor/pam00422-luminor.html,47,Switzerland,unknown,unknown,62,02-10-2026,null,1


In [0]:
df.select('Collection').distinct().display()

Collection
Radiomir
Luminor
Submersible
Luminor Due
